In [ ]:
import pandas as pd
import numpy as np
import matplotlib.pyplot as plt
import seaborn as sns
import math
import unicodedata #proporciona acceso a la base de datos de caracteres Unicode (UCD), que define las propiedades de todos los caracteres Unicode
import re
import plotly.graph_objects as go
import plotly.express as px
from plotly.subplots import make_subplots
from sklearn.metrics import mean_absolute_error, mean_squared_error
from sklearn.preprocessing import StandardScaler
from sklearn.decomposition import PCA


In [ ]:
from google.colab import drive
drive.mount('/content/drive/')

Mounted at /content/drive/


In [ ]:
%cd /content/drive/MyDrive/Datos_ICFES

/content/drive/MyDrive/Datos_ICFES


In [ ]:
%ls

 Examen_Saber_11_20222.txt   Examen_Saber_11_20251.txt
 Examen_Saber_11_20231.txt   Examen_Saber_11_20252.txt
 Examen_Saber_11_20232.txt   Saber11_limpio.csv
 Examen_Saber_11_20241.txt  'Saber11_modelo .csv'
 Examen_Saber_11_20242.txt


Explicacion:

In [ ]:
Saber11_2022_2 = pd.read_csv("Examen_Saber_11_20222.txt", sep=";")
Saber11_2023_1 = pd.read_csv("Examen_Saber_11_20231.txt", sep=";")
Saber11_2023_2 = pd.read_csv("Examen_Saber_11_20232.txt", sep=";")
Saber11_2024_1 = pd.read_csv("Examen_Saber_11_20241.txt", sep=";")
Saber11_2024_2 = pd.read_csv("Examen_Saber_11_20242.txt", sep=";")
Saber11_2025_1 = pd.read_csv("Examen_Saber_11_20251.txt", sep=";")
Saber11_2025_2 = pd.read_csv("Examen_Saber_11_20252.txt", sep=";")

# ***Analisis de datos para el dataset completo***

In [ ]:
Saber11_2022_2["Año"] = 2022
Saber11_2023_1["Año"] = 2023
Saber11_2023_2["Año"] = 2023
Saber11_2024_1["Año"] = 2024
Saber11_2024_2["Año"] = 2024
Saber11_2025_1["Año"] = 2025
Saber11_2025_2["Año"] = 2025

In [ ]:
Saber11_2022_2["Periodo"] = "2022-2"
Saber11_2023_1["Periodo"] = "2023-1"
Saber11_2023_2["Periodo"] = "2023-2"
Saber11_2024_1["Periodo"] = "2024-1"
Saber11_2024_2["Periodo"] = "2024-2"
Saber11_2025_1["Periodo"] = "2025-1"
Saber11_2025_2["Periodo"] = "2025-2"

In [ ]:
Saber11_total = pd.concat([
    Saber11_2022_2,
    Saber11_2023_1,
    Saber11_2023_2,
    Saber11_2024_1,
    Saber11_2024_2,
    Saber11_2025_1,
    Saber11_2025_2
], ignore_index=True)


In [ ]:
Saber11_total["Periodo"].value_counts().sort_index()

,count
Periodo,
2022-2,39981
2023-1,6911
2023-2,39287
2024-1,7003
2024-2,37335
2025-1,6991
2025-2,36051


In [ ]:
Saber11_total.head(5)

,periodo,estu_consecutivo,estu_estudiante,estu_tipodocumento,cole_area_ubicacion,cole_bilingue,cole_calendario,cole_caracter,cole_cod_dane_establecimiento,cole_cod_dane_sede,...,Año,Periodo,estu_grupoetnia,fami_numhermanos,estu_comunidadcampesina,estu_numhijos,estu_horastrabnoremu,fami_posicionhermanos,estu_tiempocasaacole,estu_desplazacolegio
0,20222,SB11202240585548,ESTUDIANTE,CC,RURAL,NaN,A,TÉCNICO/ACADÉMICO,276001003289,276001003289,...,2022,2022-2,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN
1,20222,SB11202240085689,ESTUDIANTE,TI,URBANO,N,A,TÉCNICO,376001006509,376001006509,...,2022,2022-2,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN
2,20222,SB11202240059520,ESTUDIANTE,TI,URBANO,N,A,ACADÉMICO,176001004973,276001043884,...,2022,2022-2,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN
3,20222,SB11202240239396,ESTUDIANTE,TI,URBANO,N,A,TÉCNICO/ACADÉMICO,376001021966,376001021966,...,2022,2022-2,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN
4,20222,SB11202240228769,ESTUDIANTE,TI,RURAL,N,A,TÉCNICO/ACADÉMICO,276520000564,276520000564,...,2022,2022-2,NaN,NaN,NaN,NaN,NaN,NaN,NaN,NaN


In [ ]:
Saber11_total.info()


<class 'pandas.core.frame.DataFrame'>
RangeIndex: 173559 entries, 0 to 173558
Data columns (total 94 columns):
 #   Column                         Non-Null Count   Dtype  
---  ------                         --------------   -----  
 0   periodo                        173559 non-null  int64  
 1   estu_consecutivo               173559 non-null  object 
 2   estu_estudiante                173559 non-null  object 
 3   estu_tipodocumento             173559 non-null  object 
 4   cole_area_ubicacion            173559 non-null  object 
 5   cole_bilingue                  142690 non-null  object 
 6   cole_calendario                173553 non-null  object 
 7   cole_caracter                  159844 non-null  object 
 8   cole_cod_dane_establecimiento  173559 non-null  int64  
 9   cole_cod_dane_sede             173559 non-null  int64  
 10  cole_cod_depto_ubicacion       173559 non-null  int64  
 11  cole_cod_mcpio_ubicacion       173559 non-null  int64  
 12  cole_codigo_icfes             

In [ ]:
variables_nulos = (
    Saber11_total.isnull().mean()
    .mul(100)
    .sort_values(ascending=False)
)

variables_nulos = variables_nulos[variables_nulos >= 30]

variables_nulos

,0
estu_etnia,97.721236
fami_posicionhermanos,85.118029
estu_horastrabnoremu,80.381887
estu_numhijos,79.731388
estu_desplazacolegio,79.731388
estu_tiempocasaacole,79.731388
fami_numhermanos,79.731388
estu_comunidadcampesina,79.731388
estu_tieneetnia,72.747020
estu_grupoetnia,49.857397


In [ ]:
#Normalizar los datos
def normalizar_texto(texto):
    """
    Convierte texto a:
    - minúsculas
    - sin tildes
    - sin caracteres especiales
    - espacios limpios
    """

    # Verificar nulos
    if pd.isna(texto):
        return texto

    # Convertir a string y minúscula
    texto = str(texto).lower()

    # Quitar tildes
    texto = unicodedata.normalize('NFD', texto)
    texto = texto.encode('ascii', 'ignore').decode('utf-8')

    # Eliminar caracteres especiales
    texto = re.sub(r'[^a-z0-9\s]', '', texto)

    # Eliminar espacios extra
    texto = re.sub(r'\s+', ' ', texto).strip()

    # Eliminar TODOS los espacios
    texto = re.sub(r'\s+', '', texto)

    return texto


# normaliza las columnas


def normalizar_columnas(df):
    """
    Normaliza todas las columnas tipo object de un DataFrame
    """

    columnas_object = df.select_dtypes(include='object').columns

    for col in columnas_object:
        df[col] = df[col].apply(normalizar_texto)

    return df

In [ ]:
(Saber11_total["cole_depto_ubicacion"].nunique())# reconocer las columnas con valores unicos
(Saber11_total["cole_cod_depto_ubicacion"].nunique())
(Saber11_total["cole_depto_ubicacion"].nunique())



1

In [ ]:
columnas_excluir = [
#Se eliminan las columnas que salieron con mas del 70% de faltantes
    "estu_etnia",
    "fami_posicionhermanos",
    "fami_numhermanos",
    "estu_comunidadcampesina",
    "estu_numhijos",
    "estu_desplazacolegio",
    "estu_tiempocasaacole",
    "estu_tieneetnia",
    "estu_grupoetnia",
    "estu_horastrabnoremu",

#Se eliminan las columnas que salieron iguales en todos los registros
    "estu_estudiante",
    "cole_cod_depto_ubicacion",
    "cole_depto_ubicacion",

#Se eliminan las columnas que no aportan mas que identificacion
    "estu_consecutivo",
    "estu_tipodocumento",
    "cole_cod_dane_establecimiento",
    "cole_cod_dane_sede",
    "cole_cod_mcpio_ubicacion",
    "cole_codigo_icfes",
    "cole_nombre_establecimiento",
    "cole_nombre_sede",
    "cole_sede_principal",
    "estu_cod_depto_presentacion",
    "estu_cod_mcpio_presentacion",
    "estu_cod_reside_depto",
    "estu_cod_reside_mcpio",
    "estu_agregado",
    "estu_depto_presentacion",

#Se eliminan las columnas que estan totalmente relacionadas al score final
    "desemp_c_naturales",
    "desemp_ingles",
    "desemp_lectura_critica",
    "desemp_matematicas",
    "desemp_sociales_ciudadanas",
    "percentil_c_naturales",
    "percentil_global",
    "percentil_ingles",
    "percentil_lectura_critica",
    "percentil_matematicas",
    "percentil_sociales_ciudadanas",
    "punt_c_naturales",
    "punt_ingles",
    "punt_lectura_critica",
    "punt_matematicas",
    "punt_sociales_ciudadanas",

#Se eliminan las columnas que no aportan al enfoque del analisis o no se conoce su formulacion
    "estu_fechanacimiento",
    "estu_generacione",
    "estu_grado",
    "estu_pais_reside",
     "estu_agregado",
    "estu_inse_individual",
    "estu_nse_establecimiento" ,
    "estu_nse_individual",
    "estu_pilopaga",
    "estu_privado_libertad",
    "estu_repite",

]

Saber11_modelo = Saber11_total.drop(
    columns=columnas_excluir,
    errors="ignore"
).copy()

def limpiar_texto(x):
    if pd.isna(x):
        return x

    x = str(x).lower().strip()
    x = unicodedata.normalize("NFKD", x)
    x = "".join(c for c in x if not unicodedata.combining(c))

    return x

columnas_texto = Saber11_modelo.select_dtypes(include="object").columns

Saber11_modelo[columnas_texto] = Saber11_modelo[columnas_texto].apply(
    lambda columna: columna.map(limpiar_texto)
)

Revisamos la cantidad de datos unicos para nacionalidad

In [ ]:
Saber11_modelo["estu_nacionalidad"].unique()

array(['colombia', 'venezuela', 'ecuador', 'espana', 'cuba',
       'estados unidos', 'vanuatu', 'peru', 'italia', 'costa rica',
       'brasil', 'francia', 'republica dominicana', 'mexico', 'bolivia',
       'india', 'belgica', 'paises bajos - holanda', 'noruega',
       'guatemala', 'honduras', 'argentina', 'cabo verde', 'chile',
       'japon', 'hungria', 'alemania', 'canada', 'uruguay'], dtype=object)

seleccionamos solo los estudiantes con nacionalidad colombiana

In [ ]:
Saber11_modelo = Saber11_modelo[
    Saber11_modelo["estu_nacionalidad"] == "colombia"
]

In [ ]:
print("Columnas en Saber11_total:", Saber11_total.shape[1])
print("Columnas en Saber11_modelo:", Saber11_modelo.shape[1])

cat_cols = Saber11_modelo.select_dtypes(include=["object"]).columns.tolist()
num_cols=Saber11_modelo.select_dtypes(include=[np.number]).columns.tolist()
print(len(cat_cols),len(num_cols))

Columnas en Saber11_total: 94
Columnas en Saber11_modelo: 42
39 3


In [ ]:
import os
from google.colab import files

# Cambiar a una carpeta segura de Colab
os.chdir("/content")

# Guardar archivo
Saber11_modelo.to_csv(
    "/content/Saber11_modelo_limpio.csv",
    index=False,
    sep=";",
    encoding="utf-8-sig"
)

# Descargar archivo
files.download("/content/Saber11_modelo_limpio.csv")

<IPython.core.display.Javascript object>

<IPython.core.display.Javascript object>

Revisamos las cantidad de columnas numericas y categoricas[link text](https://)

In [ ]:
#Tamaño del dataset filtrando solo a los estudiantes de Colombia
Saber11_modelo.shape

cat_cols = Saber11_modelo.select_dtypes(include=["object"]).columns.tolist()
num_cols = Saber11_modelo.select_dtypes(include=[np.number]).columns.tolist()

print("cantidad de columnas categoricas")
print(len(cat_cols))
print("cantidad de columnas numericas")
print(len(num_cols))

cantidad de columnas categoricas
39
cantidad de columnas numericas
3


In [ ]:

tabla_nulos = pd.DataFrame({
    "Variable": Saber11_modelo.columns,
    "Cantidad de nulos": Saber11_modelo.isnull().sum().values,
    "Porcentaje de nulos": (Saber11_modelo.isnull().mean().values * 100).round(2)
})


tabla_nulos = tabla_nulos[tabla_nulos["Cantidad de nulos"] > 0]

tabla_nulos

,Variable,Cantidad de nulos,Porcentaje de nulos
2,cole_bilingue,30425,17.86
3,cole_calendario,6,0.00
4,cole_caracter,13592,7.98
5,cole_genero,6,0.00
6,cole_jornada,8,0.00
9,estu_dedicacioninternet,18641,10.94
10,estu_dedicacionlecturadiaria,18320,10.75
11,estu_depto_reside,316,0.19
13,estu_genero,1,0.00
14,estu_horassemanatrabaja,14035,8.24


Revisamos la cantidad de nulos por columna, la mayor variable con datos nulos es cole_bilingue con 17.86%

In [ ]:
#funcion para verificar los valores permitidos
def validar_valores(df, columna, valores_permitidos):

    # Normalizar valores permitidos
    valores_permitidos = {
        normalizar_texto(v) for v in valores_permitidos
    }

    # Normalizar columna
    valores_columna = df[columna].apply(normalizar_texto)

    # Buscar inválidos
    invalidos = valores_columna[
        ~valores_columna.isin(valores_permitidos)
    ].unique()

    if len(invalidos) == 0:
        print(f"Todos los valores de '{columna}' son válidos")
    else:
        print(f"Valores inválidos encontrados en '{columna}':")
        print(invalidos)

    return invalidos

In [ ]:
def corregir_valores(df, columna, mapa_reemplazo):
    """
    Reemplaza valores inválidos o abreviaciones
    usando un diccionario de equivalencias.

    Parámetros:
    - df: DataFrame
    - columna: nombre de la columna
    - mapa_reemplazo: diccionario con equivalencias

    """

    # Normalizar claves y valores del diccionario
    mapa_normalizado = {
        normalizar_texto(k): normalizar_texto(v)
        for k, v in mapa_reemplazo.items()
    }

    # Aplicar normalización + reemplazo
    df[columna] = (
        df[columna]
        .apply(normalizar_texto)
        .replace(mapa_normalizado)
    )

    return df

def convertir_invalidos_a_nulos(df, columna, resultado_invalidos, columna_invalidos=None):

    df = df.copy()

    # Si el resultado de validar_valores es una tabla
    if isinstance(resultado_invalidos, pd.DataFrame):

        # Si no se indica la columna, usa el mismo nombre de la variable original
        if columna_invalidos is None:
            columna_invalidos = columna

        valores_invalidos = resultado_invalidos[columna_invalidos].dropna().unique()

    # Si el resultado fuera una lista o serie
    else:
        valores_invalidos = pd.Series(resultado_invalidos).dropna().unique()

    # Identificar filas inválidas
    condicion = df[columna].isin(valores_invalidos)

    cantidad = condicion.sum()

    # Convertir inválidos a nulos
    df.loc[condicion, columna] = np.nan

    print("Variable corregida:", columna)
    print("Cantidad de valores convertidos a nulos:", cantidad)

    return df

In [ ]:
def corregir_valores_invalidos(df, columna, diccionario_correcciones):

    df = df.copy()

    cantidad_antes = df[columna].isin(diccionario_correcciones.keys()).sum()

    df[columna] = df[columna].replace(diccionario_correcciones)

    print("Variable corregida:", columna)
    print("Cantidad de valores corregidos:", cantidad_antes)

    return df

In [ ]:
#Lista de municipios del valle del cauca
valores_permitidos=["alcala","andalucia","ansermanuevo","argelia","bolivar","buenaventura",
                                            "guadalajaradebuga","bugalagrande","caicedonia","cali","calima","candelaria","cartago","dagua","elaguila","elcairo","elcerrito"
,"eldovio","florida","ginebra","guacari","jamundi","lacumbre","launion","lavictoria","obando","palmira"
,"pradera","restrepo","riofrio","roldanillo","sanpedro","sevilla","toro","trujillo","tulua","ulloa",
                                            "versalles","vijes","yotoco","yumbo","zarzal"]

Normalización de los datos

In [ ]:
Saber11_modelo[["cole_mcpio_ubicacion"]].head(5)

,cole_mcpio_ubicacion
0,cali
1,cali
2,cali
3,cali
4,palmira


In [ ]:
#Normalizacion de los datos y verificacion de valores permitidos
Saber11_modelo["cole_mcpio_ubicacion"] = Saber11_modelo["cole_mcpio_ubicacion"].apply(
    normalizar_texto
)

valores_permitidos_limpios = [
    normalizar_texto(x) for x in valores_permitidos
]

mascara_no_permitidos = ~Saber11_modelo["cole_mcpio_ubicacion"].isin(
    valores_permitidos_limpios
)

cantidad_no_permitidos = mascara_no_permitidos.sum()

print("Cantidad de datos no permitidos:", cantidad_no_permitidos)

print("\nValores no permitidos y cantidad:")
print(
    Saber11_modelo.loc[
        mascara_no_permitidos,
        "cole_mcpio_ubicacion"
    ].value_counts()
)

Cantidad de datos no permitidos: 0

Valores no permitidos y cantidad:
Series([], Name: count, dtype: int64)


In [ ]:
Saber11_modelo[["estu_mcpio_presentacion"]].head(5)

,estu_mcpio_presentacion
0,cali
1,cali
2,cali
3,cali
4,palmira


In [ ]:
Saber11_modelo["estu_mcpio_presentacion"] = (
    Saber11_modelo["estu_mcpio_presentacion"]
    .astype(str)
    .str.lower()
    .str.strip()
)

mascara_no_permitidos = ~Saber11_modelo["estu_mcpio_presentacion"].isin(
    valores_permitidos
)

cantidad_no_permitidos = mascara_no_permitidos.sum()

print("Cantidad de datos no permitidos:", cantidad_no_permitidos)

print("\nValores no permitidos y cantidad:")
print(
    Saber11_modelo.loc[
        mascara_no_permitidos,
        "estu_mcpio_presentacion"
    ].value_counts()
)

Cantidad de datos no permitidos: 10987

Valores no permitidos y cantidad:
estu_mcpio_presentacion
guadalajara de buga            5375
la union                       2068
el cerrito                     2015
el aguila                       387
el cairo                        228
                               ... 
lebrija                           1
circasia                          1
villeta                           1
villa de san diego de ubate       1
puerto triunfo                    1
Name: count, Length: 142, dtype: int64


In [ ]:
#Estudiantes con diferentes
datos_validos_cole_estu_mcpio_presentacion=validar_valores(Saber11_modelo,"estu_mcpio_presentacion",valores_permitidos)
print(datos_validos_cole_estu_mcpio_presentacion)

Valores inválidos encontrados en 'estu_mcpio_presentacion':
['sanpablo' 'armenia' 'medellin' 'bucaramanga' 'sibundoy' 'bogotadc'
 'dosquebradas' 'fusagasuga' 'riosucio' 'nan' 'bosconia' 'puertotejada'
 'aguazul' 'rionegro' 'cajica' 'pereira' 'monitos' 'popayan' 'laestrella'
 'latebaida' 'sanroque' 'manizales' 'sincelejo' 'ibague' 'zipaquira'
 'barranquilla' 'duitama' 'bajobaudo' 'funza' 'lerida' 'lavega' 'pitalito'
 'mercaderes' 'tunja' 'mosquera' 'soacha' 'pasto' 'florencia' 'santamarta'
 'floridablanca' 'sanandresdetumaco' 'cartagenadeindias' 'piedecuesta'
 'chia' 'guaduas' 'libano' 'lacalera' 'valledupar' 'santanderdequilichao'
 'facatativa' 'santafedeantioquia' 'madrid' 'mocoa' 'copacabana'
 'olayaherrera' 'arauca' 'laplata' 'espinal' 'tame' 'eldoncello' 'yopal'
 'girardot' 'quibdo' 'ocana' 'orito' 'neiva' 'amalfi' 'marinilla' 'latola'
 'anserma' 'cucuta' 'riohacha' 'villadelrosario' 'apartado' 'bello'
 'puertocarreno' 'monteria' 'cienaga' 'ipiales' 'villavicencio'
 'lavirginia' 'b

In [ ]:
Saber11_modelo["estu_mcpio_reside"] = (
    Saber11_modelo["estu_mcpio_reside"]
    .astype(str)
    .str.lower()
    .str.strip()
)

mascara_no_permitidos = ~Saber11_modelo["estu_mcpio_reside"].isin(
    valores_permitidos
)

cantidad_no_permitidos = mascara_no_permitidos.sum()

print("Cantidad de datos no permitidos:", cantidad_no_permitidos)

print("\nValores no permitidos y cantidad:")
print(
    Saber11_modelo.loc[
        mascara_no_permitidos,
        "estu_mcpio_reside"
    ].value_counts()
)

Cantidad de datos no permitidos: 12340

Valores no permitidos y cantidad:
estu_mcpio_reside
guadalajara de buga    4711
el cerrito             2394
la union               1435
san pedro               729
la cumbre               541
                       ... 
la belleza                1
villeta                   1
carmen de carupa          1
sabaneta                  1
el doncello               1
Name: count, Length: 163, dtype: int64


In [ ]:
Saber11_modelo = normalizar_columnas(Saber11_modelo)

In [ ]:
#Los municipios que no están en la lista de permitidos se colocan como nan
Saber11_modelo.loc[
    ~Saber11_modelo["estu_mcpio_reside"].isin(valores_permitidos),
    "estu_mcpio_reside"
] = np.nan

Saber11_modelo["estu_mcpio_reside"] = Saber11_modelo["estu_mcpio_reside"].fillna(
    Saber11_modelo["cole_mcpio_ubicacion"]
)
Saber11_modelo.loc[
    ~Saber11_modelo["estu_mcpio_presentacion"].isin(valores_permitidos),
    "estu_mcpio_presentacion"
] = np.nan

In [ ]:
# Cantidad de valores nulos
nulos_presentacion = Saber11_modelo["estu_mcpio_presentacion"].isna().sum()
print("Nulos en estu_mcpio_presentacion:", nulos_presentacion)

# Verificar si los valores están dentro de los permitidos
verificacion_presentacion = Saber11_modelo[
    "estu_mcpio_presentacion"
].isin(valores_permitidos)

# Conteo de válidos y no válidos
print("\nVerificación municipio presentación:")
print(verificacion_presentacion.value_counts())

# Cantidad de registros no válidos
cantidad_no_validos_presentacion = (~verificacion_presentacion).sum()
print("No válidos en estu_mcpio_presentacion:", cantidad_no_validos_presentacion)

# Cantidad de valores nulos
nulos_reside = Saber11_modelo["estu_mcpio_reside"].isna().sum()
print("\nNulos en estu_mcpio_reside:", nulos_reside)

# Verificar si los valores están dentro de los permitidos
verificacion_reside = Saber11_modelo[
    "estu_mcpio_reside"
].isin(valores_permitidos)

# Conteo de válidos y no válidos
print("\nVerificación municipio residencia:")
print(verificacion_reside.value_counts())

# Cantidad de registros no válidos
cantidad_no_validos_reside = (~verificacion_reside).sum()
print("No válidos en estu_mcpio_reside:", cantidad_no_validos_reside)

Nulos en estu_mcpio_presentacion: 914

Verificación municipio presentación:
estu_mcpio_presentacion
True     169471
False       914
Name: count, dtype: int64
No válidos en estu_mcpio_presentacion: 914

Nulos en estu_mcpio_reside: 0

Verificación municipio residencia:
estu_mcpio_reside
True    170385
Name: count, dtype: int64
No válidos en estu_mcpio_reside: 0


In [ ]:
datos_validos_cole_cole_mcpio_ubicacion=validar_valores(Saber11_modelo,"cole_mcpio_ubicacion",valores_permitidos)
print(datos_validos_cole_cole_mcpio_ubicacion)

Todos los valores de 'cole_mcpio_ubicacion' son válidos
[]


In [ ]:
valores_permitidos_ubicacion=["urbano","rural"]
datos_validos_ubicacion=validar_valores(Saber11_modelo,"cole_area_ubicacion",valores_permitidos_ubicacion)
print(datos_validos_ubicacion)

Valores inválidos encontrados en 'cole_area_ubicacion':
['urbana']
['urbana']


In [ ]:
#Al verse que es la misma respuesta pero con diferente nombre solo se le cambia el nombre con el equivalente
correcciones_ubicacion = {
    "urbana": "urbano"
}

Saber11_modelo = corregir_valores_invalidos(
    Saber11_modelo,
    "cole_area_ubicacion",
    correcciones_ubicacion
)

Variable corregida: cole_area_ubicacion
Cantidad de valores corregidos: 65655


In [ ]:
#Validad que todos los estudian pertenezcan al valle del cauca

valores_permitidos_estu_depto_reside=[ "valle"]
datos_validos_estu_depto_reside=validar_valores(Saber11_modelo,"estu_depto_reside",valores_permitidos_estu_depto_reside)
print(datos_validos_estu_depto_reside)

Valores inválidos encontrados en 'estu_depto_reside':
['antioquia' 'cauca' 'santander' 'putumayo' 'bogota' 'risaralda'
 'cundinamarca' 'quindio' 'cesar' 'casanare' 'cordoba' 'caldas' 'sucre'
 'atlantico' 'boyaca' 'tolima' 'huila' 'narino' 'choco' 'magdalena'
 'bolivar' 'arauca' 'nortesantander' 'laguajira' 'meta' 'guaviare' nan
 'caqueta' 'amazonas' 'vaupes']
['antioquia' 'cauca' 'santander' 'putumayo' 'bogota' 'risaralda'
 'cundinamarca' 'quindio' 'cesar' 'casanare' 'cordoba' 'caldas' 'sucre'
 'atlantico' 'boyaca' 'tolima' 'huila' 'narino' 'choco' 'magdalena'
 'bolivar' 'arauca' 'nortesantander' 'laguajira' 'meta' 'guaviare' nan
 'caqueta' 'amazonas' 'vaupes']


In [ ]:
#Debido a que todos los estudiantes registran un colegio que pertenece al valle del cauca se decide normalizar cambiando el departamento como valle
# Crear copia de seguridad antes de modificar
Saber11_modelo["estu_depto_reside_original"] = Saber11_modelo["estu_depto_reside"]

# Normalizar toda la columna a "valle"
Saber11_modelo["estu_depto_reside"] = "valle"

In [ ]:
valores_permitidos_cole_bilingue=["n","s"]
datos_validos_cole_bilingue=validar_valores(Saber11_modelo,"cole_bilingue",valores_permitidos_cole_bilingue)
print(datos_validos_cole_bilingue)

Valores inválidos encontrados en 'cole_bilingue':
[nan]
[nan]


In [ ]:
valores_permitidos_cole_calendario=["a","b","otro"]
datos_validos_cole_cole_calendario=validar_valores(Saber11_modelo,"cole_calendario",valores_permitidos_cole_calendario)
print(datos_validos_cole_cole_calendario)

Valores inválidos encontrados en 'cole_calendario':
[nan]
[nan]


In [ ]:
valores_permitidos_cole_caracter=["academico","tecnico","tecnicoacademico","noaplica"]
datos_validos_cole_cole_caracter=validar_valores(Saber11_modelo,"cole_caracter",valores_permitidos_cole_caracter)
print(datos_validos_cole_cole_calendario)

Valores inválidos encontrados en 'cole_caracter':
[nan]
[nan]


In [ ]:
#hay una de las opciones que no se normalizo del todo, debido a que no quito el espacio, por ello se realiza este remplazo aparte
mapa_reemplazo={"no aplica":"noaplica"}
corregir_valores(Saber11_modelo,"cole_caracter",mapa_reemplazo)

,periodo,cole_area_ubicacion,cole_bilingue,cole_calendario,cole_caracter,cole_genero,cole_jornada,cole_mcpio_ubicacion,cole_naturaleza,estu_dedicacioninternet,...,fami_tieneinternet,fami_tienelavadora,fami_tienemotocicleta,fami_tieneserviciotv,fami_trabajolabormadre,fami_trabajolaborpadre,punt_global,Año,Periodo,estu_depto_reside_original
0,20222,rural,NaN,a,tecnicoacademico,mixto,noche,cali,oficial,NaN,...,NaN,no,no,NaN,trabajacomopersonaldelimpiezamantenimientosegu...,noaplica,203,2022,20222,valle
1,20222,urbano,n,a,tecnico,mixto,completa,cali,nooficial,entre1y3horas,...,si,si,si,si,nosabe,trabajaporcuentapropiaporejemploplomeroelectri...,224,2022,20222,valle
2,20222,urbano,n,a,academico,mixto,unica,cali,oficial,entre1y3horas,...,si,si,si,si,trabajacomopersonaldelimpiezamantenimientosegu...,trabajaporcuentapropiaporejemploplomeroelectri...,223,2022,20222,valle
3,20222,urbano,n,a,tecnicoacademico,mixto,tarde,cali,nooficial,entre30y60minutos,...,si,no,no,si,noaplica,noaplica,235,2022,20222,valle
4,20222,rural,n,a,tecnicoacademico,mixto,manana,palmira,oficial,masde3horas,...,si,si,si,si,tieneuntrabajodetipoauxiliaradministrativopore...,esduenodeunnegociopequenotienepocosempleadoson...,287,2022,20222,valle
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
173554,20252,urbano,n,a,academico,mixto,sabatina,buenaventura,oficial,entre1y3horas,...,si,si,no,si,trabajaporcuentapropiaporejemploplomeroelectri...,esvendedorotrabajaenatencionalpublico,162,2025,20252,valle
173555,20252,rural,NaN,a,academico,mixto,sabatina,buenaventura,oficial,30minutosomenos,...,si,si,si,si,trabajaenelhogarnotrabajaoestudia,trabajaenelhogarnotrabajaoestudia,163,2025,20252,valle
173556,20252,urbano,n,a,tecnicoacademico,mixto,unica,cali,oficial,entre1y3horas,...,no,si,no,si,trabajacomopersonaldelimpiezamantenimientosegu...,trabajaporcuentapropiaporejemploplomeroelectri...,263,2025,20252,valle
173557,20252,urbano,NaN,a,tecnico,mixto,tarde,launion,oficial,entre30y60minutos,...,si,si,si,si,esduenodeunnegociopequenotienepocosempleadoson...,esvendedorotrabajaenatencionalpublico,231,2025,20252,valle


In [ ]:
valores_permitidos_cole_genero=["femenino","masculino","mixto"]
datos_validos_cole_cole_genero=validar_valores(Saber11_modelo,"cole_genero",valores_permitidos_cole_genero)
print(datos_validos_cole_cole_genero)

Valores inválidos encontrados en 'cole_genero':
[nan]
[nan]


In [ ]:
valores_permitidos_cole_jornada=["completa", "manana", "noche", "sabatina", "tarde", "unica"]
datos_validos_cole_cole_jornada=validar_valores(Saber11_modelo,"cole_jornada",valores_permitidos_cole_jornada)
print(datos_validos_cole_cole_jornada)

Valores inválidos encontrados en 'cole_jornada':
[nan]
[nan]


In [ ]:
valores_permitidos_cole_naturaleza=[ "nooficial", "oficial"]
datos_validos_cole_naturaleza =validar_valores(Saber11_modelo,"cole_naturaleza",valores_permitidos_cole_naturaleza)
print(datos_validos_cole_naturaleza)

Todos los valores de 'cole_naturaleza' son válidos
[]


In [ ]:

valores_permitidos_estu_dedicacioninternet =["nonavegainternet", "30minutosomenos", "entre30y60minutos", "entre1y3horas", "masde3horas"]
datos_validos_estu_dedicacioninternet  =validar_valores(Saber11_modelo,"estu_dedicacioninternet",valores_permitidos_estu_dedicacioninternet)
print(datos_validos_estu_dedicacioninternet)

Valores inválidos encontrados en 'estu_dedicacioninternet':
[nan]
[nan]


In [ ]:

valores_permitidos_estu_dedicacionlecturadiaria =["noleoporentretenimiento", "30minutosomenos", "entre30y60minutos","entre1y2horas","masde2horas"]
datos_validos_estu_dedicacionlecturadiaria =validar_valores(Saber11_modelo,"estu_dedicacionlecturadiaria",valores_permitidos_estu_dedicacionlecturadiaria)
print(datos_validos_estu_dedicacionlecturadiaria)

Valores inválidos encontrados en 'estu_dedicacionlecturadiaria':
[nan]
[nan]


In [ ]:
valores_permitidos_estu_discapacidad=["s","n"]
datos_validos_estu_discapacidad=validar_valores(Saber11_modelo,"estu_discapacidad",valores_permitidos_estu_discapacidad)
print(datos_validos_estu_discapacidad)

Todos los valores de 'estu_discapacidad' son válidos
[]


In [ ]:
valores_permitidos_estu_genero =["f","m"]
datos_validos_estu_genero=validar_valores(Saber11_modelo,"estu_genero",valores_permitidos_estu_genero)
print(datos_validos_estu_genero)

Valores inválidos encontrados en 'estu_genero':
[nan]
[nan]


In [ ]:
valores_permitidos_estu_horassemanatrabaja=["0", "menosde10horas", "entre11y20horas", "entre21y30horas", "masde30horas"]
datos_validos_estu_horassemanatrabaja=validar_valores(Saber11_modelo,"estu_horassemanatrabaja",valores_permitidos_estu_horassemanatrabaja)
print(datos_validos_estu_horassemanatrabaja)

Valores inválidos encontrados en 'estu_horassemanatrabaja':
[nan]
[nan]


In [ ]:
valores_permitidos_alimentacion = [
    "1 o 2 veces por semana",
    "3 a 5 veces por semana",
    "nunca o rara vez comemos eso",
    "todos o casi todos los dias"
]


datos_validos_fami_comecarnepescadohuevo = validar_valores(
    Saber11_modelo,
    "fami_comecarnepescadohuevo",
    valores_permitidos_alimentacion
)

print(datos_validos_fami_comecarnepescadohuevo)



datos_validos_fami_comecerealfrutoslegumbre = validar_valores(
    Saber11_modelo,
    "fami_comecerealfrutoslegumbre",
    valores_permitidos_alimentacion
)

print(datos_validos_fami_comecerealfrutoslegumbre)



datos_validos_fami_comelechederivados = validar_valores(
    Saber11_modelo,
    "fami_comelechederivados",
    valores_permitidos_alimentacion
)

print(datos_validos_fami_comelechederivados)

Valores inválidos encontrados en 'fami_comecarnepescadohuevo':
[nan]
[nan]
Valores inválidos encontrados en 'fami_comecerealfrutoslegumbre':
[nan]
[nan]
Valores inválidos encontrados en 'fami_comelechederivados':
[nan]
[nan]


In [ ]:
valores_permitidos_fami_educacion = [
    "ninguno",
    "primaria incompleta",
    "primaria completa",
    "secundaria (bachillerato) incompleta",
    "secundaria (bachillerato) completa",
    "tecnica o tecnologica incompleta",
    "tecnica o tecnologica completa",
    "educacion profesional incompleta",
    "educacion profesional completa",
    "postgrado",
    "no aplica",
    "no sabe"
]

datos_validos_fami_educacionmadre = validar_valores(
    Saber11_modelo,
    "fami_educacionmadre",
    valores_permitidos_fami_educacion
)

datos_validos_fami_educacionpadre = validar_valores(
    Saber11_modelo,
    "fami_educacionpadre",
    valores_permitidos_fami_educacion
)

Valores inválidos encontrados en 'fami_educacionmadre':
[nan]
Valores inválidos encontrados en 'fami_educacionpadre':
[nan]


In [ ]:

valores_permitidos_fami_estratovivienda = [
    "estrato 1",
    "estrato 2",
    "estrato 3",
    "estrato 4",
    "estrato 5",
    "estrato 6",
    "sin estrato"
]

datos_validos_fami_estratovivienda = validar_valores(
    Saber11_modelo,
    "fami_estratovivienda",
    valores_permitidos_fami_estratovivienda
)



valores_permitidos_fami_numlibros = [
    "0 a 10 libros",
    "11 a 25 libros",
    "26 a 100 libros",
    "mas de 100 libros"
]

datos_validos_fami_numlibros = validar_valores(
    Saber11_modelo,
    "fami_numlibros",
    valores_permitidos_fami_numlibros
)



valores_permitidos_fami_personashogar = [
    "1 a 2",
    "3 a 4",
    "5 a 6",
    "7 a 8",
    "9 o mas"
]

datos_validos_fami_personashogar = validar_valores(
    Saber11_modelo,
    "fami_personashogar",
    valores_permitidos_fami_personashogar
)



valores_permitidos_fami_situacioneconomica = [
    "igual",
    "mejor",
    "peor"
]

datos_validos_fami_situacioneconomica = validar_valores(
    Saber11_modelo,
    "fami_situacioneconomica",
    valores_permitidos_fami_situacioneconomica
)


Valores inválidos encontrados en 'fami_estratovivienda':
[nan]
Valores inválidos encontrados en 'fami_numlibros':
[nan]
Valores inválidos encontrados en 'fami_personashogar':
[nan]
Valores inválidos encontrados en 'fami_situacioneconomica':
[nan]


In [ ]:
valores_permitidos_si_no = [
    "si",
    "no"
]
datos_validos_fami_tieneautomovil = validar_valores(
    Saber11_modelo,
    "fami_tieneautomovil",
    valores_permitidos_si_no
)

datos_validos_fami_tienecomputador = validar_valores(
    Saber11_modelo,
    "fami_tienecomputador",
    valores_permitidos_si_no
)
datos_validos_fami_tieneconsolavideojuegos = validar_valores(
    Saber11_modelo,
    "fami_tieneconsolavideojuegos",
    valores_permitidos_si_no
)
datos_validos_fami_tienehornomicroogas = validar_valores(
    Saber11_modelo,
    "fami_tienehornomicroogas",
    valores_permitidos_si_no
)
datos_validos_fami_tieneinternet = validar_valores(
    Saber11_modelo,
    "fami_tieneinternet",
    valores_permitidos_si_no
)
datos_validos_fami_tienelavadora = validar_valores(
    Saber11_modelo,
    "fami_tienelavadora",
    valores_permitidos_si_no
)
datos_validos_fami_tienemotocicleta = validar_valores(
    Saber11_modelo,
    "fami_tienemotocicleta",
    valores_permitidos_si_no
)
datos_validos_fami_tieneserviciotv = validar_valores(
    Saber11_modelo,
    "fami_tieneserviciotv",
    valores_permitidos_si_no
)

Valores inválidos encontrados en 'fami_tieneautomovil':
[nan]
Valores inválidos encontrados en 'fami_tienecomputador':
[nan]
Valores inválidos encontrados en 'fami_tieneconsolavideojuegos':
[nan]
Valores inválidos encontrados en 'fami_tienehornomicroogas':
[nan]
Valores inválidos encontrados en 'fami_tieneinternet':
[nan]
Valores inválidos encontrados en 'fami_tienelavadora':
[nan]
Valores inválidos encontrados en 'fami_tienemotocicleta':
[nan]
Valores inválidos encontrados en 'fami_tieneserviciotv':
[nan]


In [ ]:
valores_permitidos_fami_trabajo = [
    "es agricultor, pesquero o jornalero.",
    "es dueno de un negocio grande, tiene un cargo de nivel directivo o gerencial.",
    "es dueno de un negocio pequeno (tiene pocos empleados o no tiene, por ejemplo, tienda, papeleria, etc.",
    "es operario de maquinas o conduce vehiculos (taxista, chofer).",
    "es vendedor o trabaja en atencion al publico.",
    "tiene un trabajo de tipo auxiliar administrativo (por ejemplo, secretario o asistente).",
    "trabaja como personal de limpieza, mantenimiento, seguridad o construccion.",
    "trabaja como profesional (por ejemplo, medico, abogado, ingeniero).",
    "trabaja en el hogar, no trabaja o estudia.",
    "trabaja por cuenta propia (por ejemplo, plomero, electricista).",
    "pensionado.",
    "no sabe.",
    "no aplica"
]

datos_validos_fami_trabajolabormadre = validar_valores(
    Saber11_modelo,
    "fami_trabajolabormadre",
    valores_permitidos_fami_trabajo
)

datos_validos_fami_trabajolaborpadre = validar_valores(
    Saber11_modelo,
    "fami_trabajolaborpadre",
    valores_permitidos_fami_trabajo
)

Valores inválidos encontrados en 'fami_trabajolabormadre':
[nan 'esoperariodemaquinasoconducevehiculostaxitachofer']
Valores inválidos encontrados en 'fami_trabajolaborpadre':
['esoperariodemaquinasoconducevehiculostaxitachofer' nan]


In [ ]:
# Al verse que es la misma respuesta pero con diferente escritura,
# se cambia por el valor permitido equivalente

correcciones_fami_trabajo = {
    "esoperariodemaquinasoconducevehiculostaxitachofer":
    "esoperariodemaquinasoconducevehiculostaxistachofer"
}

Saber11_modelo = corregir_valores_invalidos(
    Saber11_modelo,
    "fami_trabajolaborpadre",
    correcciones_fami_trabajo
)

Saber11_modelo = corregir_valores_invalidos(
    Saber11_modelo,
    "fami_trabajolabormadre",
    correcciones_fami_trabajo
)

Variable corregida: fami_trabajolaborpadre
Cantidad de valores corregidos: 16342
Variable corregida: fami_trabajolabormadre
Cantidad de valores corregidos: 2654


In [ ]:
# estu_tiporemuneracion
valores_permitidos_estu_tiporemuneracion = [
    "no",
    "si,enefectivo",
    "sienespecie",
    "sienefectivoyespecie"
]

datos_validos_estu_tiporemuneracion = validar_valores(
    Saber11_modelo,
    "estu_tiporemuneracion",
    valores_permitidos_estu_tiporemuneracion
)

Valores inválidos encontrados en 'estu_tiporemuneracion':
[nan]


In [ ]:

tabla_nulos = pd.DataFrame({
    "Variable": Saber11_modelo.columns,
    "Cantidad de nulos": Saber11_modelo.isnull().sum().values,
    "Porcentaje de nulos": (Saber11_modelo.isnull().mean().values * 100).round(4)
})


tabla_nulos = tabla_nulos[tabla_nulos["Cantidad de nulos"] > 0]

tabla_nulos

,Variable,Cantidad de nulos,Porcentaje de nulos
2,cole_bilingue,30425,17.8566
3,cole_calendario,6,0.0035
4,cole_caracter,13592,7.9772
5,cole_genero,6,0.0035
6,cole_jornada,8,0.0047
9,estu_dedicacioninternet,18641,10.9405
10,estu_dedicacionlecturadiaria,18320,10.7521
13,estu_genero,1,0.0006
14,estu_horassemanatrabaja,14035,8.2372
15,estu_mcpio_presentacion,914,0.5364


In [ ]:
Saber11_modelo.info()

<class 'pandas.core.frame.DataFrame'>
Index: 170385 entries, 0 to 173558
Data columns (total 43 columns):
 #   Column                         Non-Null Count   Dtype 
---  ------                         --------------   ----- 
 0   periodo                        170385 non-null  int64 
 1   cole_area_ubicacion            170385 non-null  object
 2   cole_bilingue                  139960 non-null  object
 3   cole_calendario                170379 non-null  object
 4   cole_caracter                  156793 non-null  object
 5   cole_genero                    170379 non-null  object
 6   cole_jornada                   170377 non-null  object
 7   cole_mcpio_ubicacion           170385 non-null  object
 8   cole_naturaleza                170385 non-null  object
 9   estu_dedicacioninternet        151744 non-null  object
 10  estu_dedicacionlecturadiaria   152065 non-null  object
 11  estu_depto_reside              170385 non-null  object
 12  estu_discapacidad              170385 non-null  o

Imputacion de datos categoricos

In [ ]:
#Identificamos cuales son los datos categoricos nulos
import pandas as pd
import numpy as np

df = Saber11_modelo

# Seleccionar columnas tipo object
columnas_object = df.select_dtypes(include=["object"]).columns

# Crear tabla de nulos en variables object
tabla_object_nulos = pd.DataFrame({
    "Variable": columnas_object,
    "Nulos": df[columnas_object].isnull().sum().values,
    "Porcentaje_nulos": (df[columnas_object].isnull().mean().values * 100).round(2),
    "Categorías": [df[col].nunique(dropna=True) for col in columnas_object]
})

# Mostrar solo las que tienen nulos
tabla_object_nulos = tabla_object_nulos[tabla_object_nulos["Nulos"] > 0]

tabla_object_nulos

,Variable,Nulos,Porcentaje_nulos,Categorías
1,cole_bilingue,30425,17.86,2
2,cole_calendario,6,0.00,3
3,cole_caracter,13592,7.98,4
4,cole_genero,6,0.00,3
5,cole_jornada,8,0.00,6
8,estu_dedicacioninternet,18641,10.94,5
9,estu_dedicacionlecturadiaria,18320,10.75,5
12,estu_genero,1,0.00,2
13,estu_horassemanatrabaja,14035,8.24,5
14,estu_mcpio_presentacion,914,0.54,31


In [ ]:
#Se crea una funcion con el metodo de imputación ponderada según la distribución real ya que es mejor para mantener la proporcion original
def imputar_ponderada_categorica(df, columnas, random_state=123):

    df = df.copy()
    rng = np.random.default_rng(random_state)

    resumen = []

    for columna in columnas:

        # Convertir textos vacíos en nulos
        df[columna] = df[columna].replace(["", " ", "nan", "NaN", "NAN"], np.nan)

        nulos_antes = df[columna].isnull().sum()

        # Si no hay nulos, no hace nada
        if nulos_antes == 0:
            resumen.append({
                "Variable": columna,
                "Estado": "Sin nulos",
                "Nulos antes": 0,
                "Nulos después": 0,
                "Categorías usadas": df[columna].nunique(dropna=True)
            })
            continue

        # Distribución real de los valores existentes
        distribucion = df[columna].dropna().value_counts(normalize=True)

        # Si no hay datos válidos para imputar, no puede imputar
        if len(distribucion) == 0:
            resumen.append({
                "Variable": columna,
                "Estado": "No imputada, sin valores válidos",
                "Nulos antes": nulos_antes,
                "Nulos después": nulos_antes,
                "Categorías usadas": 0
            })
            continue

        # Valores y probabilidades
        valores = distribucion.index.to_numpy()
        probabilidades = distribucion.values

        # Imputar los nulos según la proporción real
        mascara_nulos = df[columna].isnull()

        df.loc[mascara_nulos, columna] = rng.choice(
            valores,
            size=nulos_antes,
            p=probabilidades
        )

        nulos_despues = df[columna].isnull().sum()

        resumen.append({
            "Variable": columna,
            "Estado": "Imputada",
            "Nulos antes": nulos_antes,
            "Nulos después": nulos_despues,
            "Categorías usadas": len(distribucion)
        })

    resumen = pd.DataFrame(resumen)

    return df, resumen

In [ ]:
# Lista de variables object con nulos
columnas_object_con_nulos = tabla_object_nulos["Variable"].tolist()

# Aplicar imputación ponderada
Saber11_modelo, resumen_imputacion = imputar_ponderada_categorica(
    Saber11_modelo,
    columnas_object_con_nulos,
    random_state=123
)

resumen_imputacion

,Variable,Estado,Nulos antes,Nulos después,Categorías usadas
0,cole_bilingue,Imputada,30425,0,2
1,cole_calendario,Imputada,6,0,3
2,cole_caracter,Imputada,13592,0,4
3,cole_genero,Imputada,6,0,3
4,cole_jornada,Imputada,8,0,6
5,estu_dedicacioninternet,Imputada,18641,0,5
6,estu_dedicacionlecturadiaria,Imputada,18320,0,5
7,estu_genero,Imputada,1,0,2
8,estu_horassemanatrabaja,Imputada,14035,0,5
9,estu_mcpio_presentacion,Imputada,914,0,31


In [ ]:
Saber11_modelo.isnull().sum().sum()

np.int64(0)

In [ ]:
#descargamos el dataset ya imputado, sin nulos y variables inconsistentes
from google.colab import files

# Guardar base imputada como CSV
Saber11_modelo.to_csv(
    "/content/Saber11_modelo_imputado.csv",
    index=False,
    sep=";",
    encoding="utf-8-sig"
)

# Descargar archivo
files.download("/content/Saber11_modelo_imputado.csv")

<IPython.core.display.Javascript object>

<IPython.core.display.Javascript object>

In [ ]:
Saber11_modelo.describe()

,periodo,punt_global,Año
count,170385.000000,170385.000000,170385.000000
mean,20237.051965,256.365273,2023.517399
std,10.932061,52.593697,1.098126
min,20222.000000,0.000000,2022.000000
25%,20231.000000,216.000000,2023.000000
50%,20241.000000,253.000000,2024.000000
75%,20242.000000,294.000000,2024.000000
max,20252.000000,494.000000,2025.000000


In [ ]:
Saber11_modelo.duplicated().sum()

np.int64(0)

In [ ]:
Saber11_modelo["punt_global"].describe()

,punt_global
count,170385.000000
mean,256.365273
std,52.593697
min,0.000000
25%,216.000000
50%,253.000000
75%,294.000000
max,494.000000


In [ ]:
puntaje_anual = Saber11_modelo.groupby("Año")["punt_global"].agg(
    cantidad="count",
    promedio="mean",
    mediana="median",
    desviacion="std"
).reset_index()

puntaje_anual

,Año,cantidad,promedio,mediana,desviacion
0,2022,39404,247.857730,245.0,49.194516
1,2023,45475,256.649016,253.0,51.885824
2,2024,43451,258.668753,257.0,53.559711
3,2025,42055,261.649768,259.0,54.435190


In [ ]:
tabla_frecuencia = Saber11_modelo["estu_mcpio_reside"].value_counts().reset_index()
tabla_frecuencia.columns = ["Municipio", "Frecuencia"]
tabla_frecuencia["Porcentaje"] = (
    tabla_frecuencia["Frecuencia"] /
    tabla_frecuencia["Frecuencia"].sum() * 100
).round(2)
print(tabla_frecuencia)

            Municipio  Frecuencia  Porcentaje
0                cali       79196       46.48
1        buenaventura       13632        8.00
2             palmira       13445        7.89
3               tulua        8517        5.00
4             jamundi        6315        3.71
5             cartago        5515        3.24
6   guadalajaradebuga        4712        2.77
7               yumbo        4517        2.65
8          candelaria        4308        2.53
9             florida        2596        1.52
10          elcerrito        2430        1.43
11             zarzal        1868        1.10
12            pradera        1804        1.06
13              dagua        1696        1.00
14         roldanillo        1622        0.95
15            guacari        1467        0.86
16            launion        1436        0.84
17            sevilla        1411        0.83
18         caicedonia        1354        0.79
19       bugalagrande         916        0.54
20            ginebra         886 

In [ ]:
variables_institucionales = [
    "cole_area_ubicacion",
    "cole_bilingue",
    "cole_calendario",
    "cole_caracter",
    "cole_genero",
    "cole_jornada",
    "cole_naturaleza",

]

Saber11_modelo["cole_area_ubicacion"] = Saber11_modelo["cole_area_ubicacion"].replace("URBANA", "URBANO")
for var in variables_institucionales:
    print("\nVariable:", var)
    display(
        Saber11_modelo.groupby(var)["punt_global"]
        .agg(cantidad="count", promedio="mean", mediana="median")
        .sort_values("promedio", ascending=False)
    )


Variable: cole_area_ubicacion


,cantidad,promedio,mediana
cole_area_ubicacion,,,
urbano,147559,258.034061,256.0
rural,22826,245.577368,240.0



Variable: cole_bilingue


,cantidad,promedio,mediana
cole_bilingue,,,
s,4498,284.23277,284.0
n,165887,255.60965,253.0



Variable: cole_calendario


...

,cantidad,promedio,mediana
cole_genero,,,
masculino,1048,295.480916,297.0
femenino,2273,284.615046,289.0
mixto,167064,255.735544,253.0



Variable: cole_jornada


,cantidad,promedio,mediana
cole_jornada,,,
completa,14852,300.385537,305.0
manana,94275,256.212782,254.0
unica,35416,255.920883,253.0
tarde,13745,251.012223,248.0
noche,7071,212.803422,207.0
sabatina,5026,208.201552,203.0



Variable: cole_naturaleza


,cantidad,promedio,mediana
cole_naturaleza,,,
nooficial,53866,272.010693,272.0
oficial,116519,249.132493,246.0


In [ ]:
variables_sociodemograficas = [
    "estu_dedicacioninternet",
    "estu_dedicacionlecturadiaria",
    "estu_discapacidad",
    "estu_genero",
    "estu_horassemanatrabaja",
    "estu_mcpio_reside",
    "estu_nacionalidad",
    "estu_tiporemuneracion"
]

Saber11_modelo["estu_nacionalidad"] = Saber11_modelo["estu_nacionalidad"].replace("ESPAŃA", "ESPAÑA")


for var in variables_sociodemograficas:
    print("\nVariable:", var)
    display(
        Saber11_modelo.groupby(var)["punt_global"]
        .agg(cantidad="count", promedio="mean", mediana="median")
        .sort_values("promedio", ascending=False)
    )



Variable: estu_dedicacioninternet


,cantidad,promedio,mediana
estu_dedicacioninternet,,,
masde3horas,46687,264.048172,263.0
entre1y3horas,57405,263.026252,261.0
entre30y60minutos,38652,250.353720,247.0
30minutosomenos,21472,239.029341,233.0
nonavegainternet,6169,234.243475,228.0



Variable: estu_dedicacionlecturadiaria


,cantidad,promedio,mediana
estu_dedicacionlecturadiaria,,,
masde2horas,6962,272.585895,275.0
entre1y2horas,15789,266.973526,268.0
entre30y60minutos,40341,265.575395,265.0
30minutosomenos,62105,252.322051,248.0
noleoporentretenimiento,45188,247.494268,243.0



Variable: estu_discapacidad


...

,cantidad,promedio,mediana
estu_mcpio_reside,,,
guadalajaradebuga,4712,271.005730,270.0
palmira,13445,268.774637,269.0
jamundi,6315,263.227870,261.0
calima,780,262.583333,263.0
ginebra,886,262.295711,261.5
cali,79196,261.721526,260.0
tulua,8517,261.700129,260.0
roldanillo,1622,259.205302,257.0
eldovio,374,257.860963,257.0



Variable: estu_nacionalidad


,cantidad,promedio,mediana
estu_nacionalidad,,,
colombia,170385,256.365273,253.0



Variable: estu_tiporemuneracion


,cantidad,promedio,mediana
estu_tiporemuneracion,,,
no,117070,259.352524,257.0
sienefectivo,47603,250.190135,247.0
sienespecie,2976,247.546371,246.0
sienefectivoyespecie,2736,245.576754,242.0


In [ ]:
variables_familiares = [
    "estu_inse_individual",
    "estu_nse_individual",
    "fami_educacionmadre",
    "fami_educacionpadre",
    "fami_estratovivienda",
    "fami_numlibros",
    "fami_personashogar",
    "fami_cuartoshogar",
    "fami_situacioneconomica",
    "fami_tieneinternet",
    "fami_tienecomputador",
    "fami_tieneautomovil",
    "fami_tienelavadora",
    "fami_tienemotocicleta",
    "fami_tieneserviciotv"
]

In [ ]:
variables_familiares_cat = [
    "fami_educacionmadre",
    "fami_educacionpadre",
    "fami_estratovivienda",
    "fami_numlibros",
    "fami_personashogar",
    "fami_cuartoshogar",
    "fami_situacioneconomica",
    "fami_tieneinternet",
    "fami_tienecomputador",
    "fami_tieneautomovil",
    "fami_tienelavadora",
    "fami_tienemotocicleta",
    "fami_tieneserviciotv"
]

for var in variables_familiares_cat:
    print("\nVariable:", var)
    display(
        Saber11_modelo.groupby(var)["punt_global"]
        .agg(cantidad="count", promedio="mean", mediana="median")
        .sort_values("promedio", ascending=False)
    )


Variable: fami_educacionmadre


,cantidad,promedio,mediana
fami_educacionmadre,,,
postgrado,3773,306.075272,316.0
educacionprofesionalcompleta,22610,277.399204,280.0
educacionprofesionalincompleta,5469,272.989760,275.0
tecnicaotecnologicacompleta,18125,269.784386,270.0
tecnicaotecnologicaincompleta,5890,262.473514,263.0
nosabe,6714,260.609026,260.0
secundariabachilleratocompleta,56706,252.564297,250.0
secundariabachilleratoincompleta,23151,244.579716,241.0
primariacompleta,9241,237.930311,233.0



Variable: fami_educacionpadre


,cantidad,promedio,mediana
fami_educacionpadre,,,
postgrado,3401,310.655690,322.0
educacionprofesionalcompleta,17715,277.789162,280.0
educacionprofesionalincompleta,3807,276.593906,280.0
tecnicaotecnologicacompleta,13049,271.407847,272.0
tecnicaotecnologicaincompleta,4157,262.697378,263.0
nosabe,17338,259.762891,258.0
noaplica,2541,258.896497,258.0
secundariabachilleratocompleta,48150,253.720021,252.0
secundariabachilleratoincompleta,25542,248.742972,246.0



Variable: fami_estratovivienda


...

,cantidad,promedio,mediana
fami_tienelavadora,,,
si,136463,259.657065,257.0
no,33922,243.122900,239.0



Variable: fami_tienemotocicleta


,cantidad,promedio,mediana
fami_tienemotocicleta,,,
no,77277,256.928349,253.0
si,93108,255.897936,254.0



Variable: fami_tieneserviciotv


,cantidad,promedio,mediana
fami_tieneserviciotv,,,
si,126362,257.979875,255.0
no,44023,251.730777,249.0


In [ ]:
variables_numericas = Saber11_modelo.select_dtypes(include=["int64", "float64"])

correlaciones = variables_numericas.corr()["punt_global"].sort_values(ascending=False)

correlaciones

,punt_global
punt_global,1.000000
Año,0.089406
periodo,0.081313


# ***Graficas Representativas para diapostivas***

In [ ]:
promedio_municipio = (
    Saber11_modelo
    .groupby("estu_mcpio_reside", as_index=False)["punt_global"]
    .mean()
)

promedio_municipio.columns = ["municipio", "promedio_punt_global"]


promedio_municipio["municipio"] = (
    promedio_municipio["municipio"]
    .astype(str)
    .str.replace("_", " ", regex=False)
    .str.title()
)


top_5_mejores = promedio_municipio.sort_values(
    by="promedio_punt_global",
    ascending=False
).head(5)

top_5_mejores["grupo"] = "Mejor promedio"


top_5_peores = promedio_municipio.sort_values(
    by="promedio_punt_global",
    ascending=True
).head(5)

top_5_peores["grupo"] = "Peor promedio"


top_municipios = pd.concat(
    [top_5_mejores, top_5_peores],
    ignore_index=True
)


fig = px.bar(
    top_municipios,
    x="promedio_punt_global",
    y="municipio",
    orientation="h",
    facet_col="grupo",
    text=top_municipios["promedio_punt_global"].round(1),
    color="municipio",
    color_discrete_sequence=px.colors.qualitative.Pastel,
    title="Top 5 mejores y peores municipios según promedio de puntaje global"
)

fig.update_traces(
    textposition="outside",
    marker_line_width=1.2,
    marker_line_color="rgba(0,0,0,0.25)"
)

fig.update_layout(
    font=dict(
        family="DejaVu Serif",
        size=13
    ),
    title=dict(
        text="Top 5 mejores y peores municipios según promedio de puntaje global",
        font=dict(
            family="DejaVu Serif",
            size=20
        ),
        x=0.5
    ),
    xaxis_title="Promedio puntaje global",
    yaxis_title="Municipio de residencia",
    plot_bgcolor="white",
    paper_bgcolor="white",
    showlegend=False,
    height=500,
    width=1100,
    margin=dict(l=180, r=80, t=90, b=60)
)

fig.update_xaxes(
    showgrid=True,
    gridcolor="lightgray",
    matches=None
)

fig.update_yaxes(
    autorange="reversed",
    automargin=True
)

fig.for_each_annotation(
    lambda a: a.update(
        text=a.text.split("=")[-1],
        font=dict(
            family="DejaVu Serif",
            size=15
        )
    )
)

fig.show()

In [ ]:
paleta_estratos = [
    "#90CAF9",
    "#64B5F6",
    "#42A5F5",
    "#1E88E5",
    "#1976D2",
    "#1565C0",
    "#0D47A1"
]

promedio_estrato = (
    Saber11_modelo
    .groupby("fami_estratovivienda", as_index=False)["punt_global"]
    .mean()
)

promedio_estrato.columns = [
    "estrato_vivienda",
    "promedio_punt_global"
]

promedio_estrato = promedio_estrato.sort_values(
    by="promedio_punt_global",
    ascending=False
)

promedio_estrato["estrato_vivienda"] = (
    promedio_estrato["estrato_vivienda"]
    .astype(str)
    .str.replace("_", " ", regex=False)
    .str.title()
)

fig = px.bar(
    promedio_estrato,
    x="estrato_vivienda",
    y="promedio_punt_global",
    text=promedio_estrato["promedio_punt_global"].round(1),
    color="estrato_vivienda",
    color_discrete_sequence=paleta_estratos,
    title="Puntaje global promedio por estrato"
)

fig.update_traces(
    textposition="outside",
    marker_line_width=1,
    marker_line_color="rgba(0,0,0,0.15)"
)

fig.update_layout(
    font=dict(
        family="DejaVu Serif",
        size=14,
        color="#1B263B"
    ),

    title=dict(
        text="Puntaje global promedio por estrato",
        font=dict(
            family="DejaVu Serif",
            size=22
        ),
        x=0.5
    ),

    xaxis_title="Estrato de vivienda",
    yaxis_title="Promedio puntaje global",

    plot_bgcolor="white",
    paper_bgcolor="white",

    showlegend=False,

    height=500,
    width=850,

    margin=dict(
        l=70,
        r=40,
        t=60,
        b=70
    )
)

fig.update_xaxes(
    showgrid=False,
    tickfont=dict(size=13)
)

fig.update_yaxes(
    showgrid=True,
    gridcolor="rgba(200,200,200,0.35)"
)

fig.show()

In [ ]:

fig = px.box(
    Saber11_modelo,
    y="punt_global",
    title="Boxplot del puntaje global",
    points="outliers"
)

fig.update_layout(
    width=800,
    height=800,
    yaxis_title="Puntaje global",
    xaxis_title="",
    template="plotly_white"
)

fig.show()

In [ ]:

df_tiempo = Saber11_modelo[["periodo", "punt_global"]].copy()


df_tiempo["periodo"] = df_tiempo["periodo"].astype(str)

df_tiempo["periodo_grafica"] = (
    df_tiempo["periodo"].str[:4] + "_" + df_tiempo["periodo"].str[-1]
)


promedio_tiempo = (
    df_tiempo
    .groupby(["periodo", "periodo_grafica"], as_index=False)["punt_global"]
    .mean()
)

promedio_tiempo.columns = ["periodo", "periodo_grafica", "promedio_punt_global"]


promedio_tiempo["periodo"] = promedio_tiempo["periodo"].astype(int)

promedio_tiempo = promedio_tiempo.sort_values("periodo")


fig = px.line(
    promedio_tiempo,
    x="periodo_grafica",
    y="promedio_punt_global",
    markers=True,
    text=promedio_tiempo["promedio_punt_global"].round(1),
    title="Promedio de puntaje global por periodo"
)

fig.update_traces(
    line=dict(
        color="#168AAD",
        width=3
    ),
    marker=dict(
        size=9,
        color="#F4978E",
        line=dict(
            width=1.5,
            color="rgba(0,0,0,0.35)"
        )
    ),
    textposition="top center"
)

fig.update_layout(
    font=dict(
        family="DejaVu Serif",
        size=13
    ),
    title=dict(
        text="Promedio de puntaje global por periodo",
        font=dict(
            family="DejaVu Serif",
            size=20
        ),
        x=0.5
    ),
    xaxis_title="Periodo",
    yaxis_title="Promedio puntaje global",
    plot_bgcolor="white",
    paper_bgcolor="white",
    height=550,
    width=1000,
    margin=dict(l=80, r=80, t=90, b=80)
)

fig.update_xaxes(
    categoryorder="array",
    categoryarray=promedio_tiempo["periodo_grafica"],
    showgrid=False
)

fig.update_yaxes(
    showgrid=True,
    gridcolor="lightgray"
)

fig.show()

In [ ]:
df_jornada = Saber11_modelo[["cole_jornada", "punt_global"]].copy()


orden_jornada = (
    df_jornada
    .groupby("cole_jornada")["punt_global"]
    .mean()
    .sort_values(ascending=False)
    .index
    .tolist()
)

# Paleta
paleta_jornada = [
    "#EA698B",
    "#D55D92",
    "#C05299",
    "#AC46A1",
    "#973AA8",
    "#822FAF",
]

fig = go.Figure()

for jornada, color in zip(orden_jornada, paleta_jornada):
    datos = df_jornada.loc[
        df_jornada["cole_jornada"] == jornada,
        "punt_global"
    ]

    fig.add_trace(
        go.Box(
            y=datos,
            name=str(jornada),
            fillcolor=color,
            marker_color=color,
            line=dict(color="rgba(0,0,0,0.45)", width=1.2),
            boxmean=True
        )
    )

fig.update_layout(
    title=dict(
        text="Distribución del puntaje global según jornada del colegio",
        font=dict(
            family="DejaVu Serif",
            size=20
        ),
        x=0.5
    ),
    font=dict(
        family="DejaVu Serif",
        size=13
    ),
    xaxis_title="Jornada del colegio",
    yaxis_title="Puntaje global",
    plot_bgcolor="white",
    paper_bgcolor="white",
    showlegend=False,
    height=550,
    width=1000,
    margin=dict(l=80, r=80, t=90, b=80)
)

fig.update_xaxes(
    showgrid=False
)

fig.update_yaxes(
    showgrid=True,
    gridcolor="lightgray"
)

fig.show()

In [ ]:
paleta_educacion = ["#E7C6FF", "#4A7B9D"]


madre = (
    Saber11_modelo
    .groupby("fami_educacionmadre", as_index=False)["punt_global"]
    .mean()
)

madre.columns = ["nivel_educacion", "promedio_punt_global"]
madre["familiar"] = "Madre"


padre = (
    Saber11_modelo
    .groupby("fami_educacionpadre", as_index=False)["punt_global"]
    .mean()
)

padre.columns = ["nivel_educacion", "promedio_punt_global"]
padre["familiar"] = "Padre"



educacion_familia = pd.concat([madre, padre], ignore_index=True)


orden_niveles = (
    educacion_familia
    .groupby("nivel_educacion")["promedio_punt_global"]
    .mean()
    .sort_values(ascending=False)
    .index
    .tolist()
)



fig = px.bar(
    educacion_familia,
    x="nivel_educacion",
    y="promedio_punt_global",
    color="familiar",
    barmode="group",
    text=educacion_familia["promedio_punt_global"].round(1),
    category_orders={
        "nivel_educacion": orden_niveles,
        "familiar": ["Madre", "Padre"]
    },
    color_discrete_sequence=paleta_educacion,
    title="Promedio de puntaje global según educación de madre y padre"
)

fig.update_traces(
    textposition="outside",
    marker_line_width=1.2,
    marker_line_color="rgba(0,0,0,0.25)"
)

fig.update_layout(
    font=dict(
        family="DejaVu Serif",
        size=13
    ),
    title=dict(
        text="Promedio de puntaje global según educación de madre y padre",
        font=dict(
            family="DejaVu Serif",
            size=20
        ),
        x=0.5
    ),
    xaxis_title="Nivel educativo",
    yaxis_title="Promedio puntaje global",
    legend_title_text="Familiar",
    plot_bgcolor="white",
    paper_bgcolor="white",
    height=600,
    width=1100,
    margin=dict(l=80, r=80, t=90, b=180)
)

fig.update_xaxes(
    tickangle=-45,
    showgrid=False
)

fig.update_yaxes(
    showgrid=True,
    gridcolor="lightgray"
)

fig.show()

In [ ]:
paleta_servicios = [
    "#884AB2",
    "#D1105A"
]


variables_servicios = [
    "fami_tienecomputador",
    "fami_tieneinternet",
    "fami_tieneserviciotv",

]


df_servicios = Saber11_modelo[
    variables_servicios + ["punt_global"]
].melt(
    id_vars="punt_global",
    value_vars=variables_servicios,
    var_name="servicio",
    value_name="respuesta"
)


promedio_servicios = (
    df_servicios
    .groupby(["servicio", "respuesta"], as_index=False)["punt_global"]
    .mean()
)

promedio_servicios.columns = [
    "servicio",
    "respuesta",
    "promedio_punt_global"
]


promedio_servicios["servicio"] = (
    promedio_servicios["servicio"]
    .replace({
        "fami_tienecomputador": "Tiene computador",
        "fami_tieneinternet": "Tiene internet",
        "fami_tieneserviciotv": "Tiene servicio TV",

    })
)


promedio_servicios["respuesta"] = (
    promedio_servicios["respuesta"]
    .replace({
        "s": "Sí",
        "n": "No"
    })
)


orden_servicios = [
    "Tiene computador",
    "Tiene internet",
    "Tiene servicio TV",
    "Tiene consola de videojuegos"
]

orden_respuesta = ["No", "Sí"]


fig = px.bar(
    promedio_servicios,
    x="servicio",
    y="promedio_punt_global",
    color="respuesta",
    barmode="group",
    text=promedio_servicios["promedio_punt_global"].round(1),
    category_orders={
        "servicio": orden_servicios,
        "respuesta": orden_respuesta
    },
    color_discrete_sequence=paleta_servicios,
    title="Promedio de puntaje global según acceso a servicios del hogar"
)

fig.update_traces(
    textposition="outside",
    marker_line_width=1.2,
    marker_line_color="rgba(0,0,0,0.25)"
)

fig.update_layout(
    font=dict(
        family="DejaVu Serif",
        size=13
    ),
    title=dict(
        text="Promedio de puntaje global según acceso a servicios del hogar",
        font=dict(
            family="DejaVu Serif",
            size=20
        ),
        x=0.5
    ),
    xaxis_title="Servicio del hogar",
    yaxis_title="Promedio puntaje global",
    legend_title_text="Respuesta",
    plot_bgcolor="white",
    paper_bgcolor="white",
    height=550,
    width=1000,
    margin=dict(l=80, r=80, t=90, b=90)
)

fig.update_xaxes(
    showgrid=False
)

fig.update_yaxes(
    showgrid=True,
    gridcolor="lightgray"
)

fig.show()

In [ ]:
paleta_educacion = ["#E7C6FF", "#4A7B9D"]

# Datos de madre
madre = Saber11_modelo[["fami_educacionmadre", "punt_global"]].copy()
madre = madre.rename(columns={"fami_educacionmadre": "nivel_educacion"})
madre["familiar"] = "Madre"

# Datos de padre
padre = Saber11_modelo[["fami_educacionpadre", "punt_global"]].copy()
padre = padre.rename(columns={"fami_educacionpadre": "nivel_educacion"})
padre["familiar"] = "Padre"

# Unir datos
educacion_familia = pd.concat([madre, padre], ignore_index=True)

# Quitar datos faltantes
educacion_familia = educacion_familia.dropna()

# Ordenar niveles educativos por promedio de puntaje
orden_niveles = (
    educacion_familia
    .groupby("nivel_educacion")["punt_global"]
    .mean()
    .sort_values(ascending=False)
    .index
)

# Gráfica de violín
fig = px.violin(
    educacion_familia,
    x="nivel_educacion",
    y="punt_global",
    color="familiar",
    violinmode="group",
    box=True,
    points=False,
    category_orders={
        "nivel_educacion": orden_niveles,
        "familiar": ["Madre", "Padre"]
    },
    color_discrete_sequence=paleta_educacion,
    title="Distribución del puntaje global según educación de madre y padre"
)

fig.update_layout(
    font_family="DejaVu Serif",
    title_x=0.5,
    xaxis_title="Nivel educativo",
    yaxis_title="Puntaje global",
    legend_title_text="Familiar",
    plot_bgcolor="white",
    paper_bgcolor="white",
    height=600,
    width=1100
)

fig.update_xaxes(tickangle=-45)
fig.update_yaxes(showgrid=True, gridcolor="lightgray")

fig.show()

## Modelos de Machine Learning

In [ ]:
# División de los datos en entrenamiento y testing
from sklearn.model_selection import train_test_split

# Métricas para modelos de regresión
from sklearn.metrics import mean_absolute_error, mean_squared_error, r2_score

# Herramientas para preprocesamiento
from sklearn.compose import ColumnTransformer
from sklearn.preprocessing import OneHotEncoder, StandardScaler
from sklearn.pipeline import Pipeline

# Aprendizaje supervisado - modelos de regresión
from sklearn.tree import DecisionTreeRegressor
from sklearn.ensemble import RandomForestRegressor
from sklearn.linear_model import LinearRegression
from sklearn.ensemble import GradientBoostingRegressor

# Visualización y gráficos
import matplotlib.pyplot as plt

# Librerías base
import pandas as pd
import numpy as np
import seaborn as sns

In [ ]:
#Debido a que tenemos variables booleanas en nuestro dataset pero estos aparecen como tipo object distinguiremos caules son estas columnas
# Crear copia de trabajo
df = Saber11_modelo.copy()

# Buscar columnas object
columnas_object = df.select_dtypes(include=["object"]).columns

columnas_booleanas = []

for col in columnas_object:
    valores = set(df[col].dropna().unique())

    if valores.issubset({"si", "no"}) and len(valores) <= 2:
        columnas_booleanas.append(col)

print("Variables booleanas encontradas:")
print(columnas_booleanas)
print("Cantidad:", len(columnas_booleanas))

for col in columnas_booleanas:
    df[col] = df[col].map({
        "si": 1,
        "no": 0
    })


In [ ]:
df[columnas_booleanas].dtypes

In [ ]:
# Variables predictoras: todas menos punt_global
X = df.drop(columns=["punt_global"])

# Variable objetivo
y = df["punt_global"]

print("Tamaño de y:", y.shape)
print("Tamaño de X:", X.shape)

In [ ]:
# Dividir los datos en conjuntos de entrenamiento y prueba
X_train, X_test, y_train, y_test = train_test_split(X, y, test_size=0.2, random_state=42)

print("Tamaño de X_train:", X_train.shape)
print("Tamaño de X_test:", X_test.shape)
print("Tamaño de y_train:", y_train.shape)
print("Tamaño de y_test:", y_test.shape)

In [ ]:
# Distribución de y_train
sns.histplot(y_train, kde=True)
plt.title('Distribución de y_train')
plt.show()

# Distribución de y_test
sns.histplot(y_test, kde=True)
plt.title('Distribución de y_test')
plt.show()

In [ ]:
#distinguimos cuales son las variables numericas y cuales son las categoricas
variables_numericas = X_train.select_dtypes(include=["int64", "float64", "int32", "float32"]).columns
variables_categoricas = X_train.select_dtypes(include=["object"]).columns

print("Cantidad de variables numéricas:", len(variables_numericas))
print("Cantidad de variables categóricas:", len(variables_categoricas))

print("\nVariables numéricas:")
print(variables_numericas.tolist())

print("\nVariables categóricas:")
print(variables_categoricas.tolist())

In [ ]:
#Para el DecisionTreeRegressor, el RandomForestRegressor y el GradientBoostingRegressor no es necesario escalar,
#por ende unicamente se vuelven numericas las categoricas por medio de OneHotEncoder que las convierten en secuencia de 1 y 0
preprocesador_arboles = ColumnTransformer(
    transformers=[
        ("num", "passthrough", variables_numericas),
        ("cat", OneHotEncoder(handle_unknown="ignore", sparse_output=False), variables_categoricas)
    ]
)

In [ ]:
#Para regresion lineal se escala las variables numericas
preprocesador_lineal = ColumnTransformer(
    transformers=[
        ("num", StandardScaler(), variables_numericas),
        ("cat", OneHotEncoder(handle_unknown="ignore", sparse_output=False), variables_categoricas)
    ]
)

In [ ]:
# Para modelos basados en árboles
X_train_arboles = preprocesador_arboles.fit_transform(X_train)
X_test_arboles = preprocesador_arboles.transform(X_test)

# Para regresión lineal
X_train_lineal = preprocesador_lineal.fit_transform(X_train)
X_test_lineal = preprocesador_lineal.transform(X_test)

print("X_train_arboles:", X_train_arboles.shape)
print("X_test_arboles:", X_test_arboles.shape)

print("X_train_lineal:", X_train_lineal.shape)
print("X_test_lineal:", X_test_lineal.shape)

In [ ]:
# Crear los modelos de regresión
model_DT  = DecisionTreeRegressor(random_state=0)
model_RF  = RandomForestRegressor(random_state=0)
model_LR  = LinearRegression()  # El modelo de regresión lineal no necesita random_state
model_GB  = GradientBoostingRegressor(random_state=0)



In [ ]:
# Lista de modelos
modelos = [
    (model_DT, "Decision Tree"),
    (model_RF, "Random Forest"),
    (model_LR, "Linear Regression"),
    (model_GB, "Gradient Boosting")
]

In [ ]:
def evaluar_modelo(modelo, X_train, X_test, y_train, y_test, nombre):

    # Entrenar modelo
    modelo.fit(X_train, y_train)

    # Realizar predicciones
    y_pred = modelo.predict(X_test)

    # Calcular métricas
    mae = mean_absolute_error(y_test, y_pred)
    mse = mean_squared_error(y_test, y_pred)
    rmse = np.sqrt(mse)
    r2 = r2_score(y_test, y_pred)

    print(f"Resultados para {nombre}:")
    print(f"MAE:  {mae:.4f}")
    print(f"MSE:  {mse:.4f}")
    print(f"RMSE: {rmse:.4f}")
    print(f"R2:   {r2:.4f}")
    print("-" * 40)

    return {
        "Modelo": nombre,
        "MAE": mae,
        "MSE": mse,
        "RMSE": rmse,
        "R2": r2
    }

In [ ]:
resultados = []

# Árbol de decisión
resultados.append(
    evaluar_modelo(
        model_DT,
        X_train_arboles,
        X_test_arboles,
        y_train,
        y_test,
        "Árbol de decisión"
    )
)

# Random Forest
resultados.append(
    evaluar_modelo(
        model_RF,
        X_train_arboles,
        X_test_arboles,
        y_train,
        y_test,
        "Random Forest"
    )
)

# Regresión lineal múltiple
resultados.append(
    evaluar_modelo(
        model_LR,
        X_train_lineal,
        X_test_lineal,
        y_train,
        y_test,
        "Regresión lineal múltiple"
    )
)

# Gradient Boosting
resultados.append(
    evaluar_modelo(
        model_GB,
        X_train_arboles,
        X_test_arboles,
        y_train,
        y_test,
        "Gradient Boosting"
    )
)

In [ ]:
#Busca automáticamente los mejores parámetros para arbol de decision
from sklearn.model_selection import GridSearchCV

param_grid_dt = {
    "max_depth": [5, 10, 20, None],
    "min_samples_split": [2, 10, 50],
    "min_samples_leaf": [1, 5, 20]
}

grid_dt = GridSearchCV(
    DecisionTreeRegressor(random_state=0),
    param_grid_dt,
    cv=3,
    scoring="neg_mean_squared_error",
    n_jobs=-1
)

grid_dt.fit(X_train_arboles, y_train)

print("Mejores parámetros para Árbol de Decisión:")
print(grid_dt.best_params_)

In [ ]:
#Busca automáticamente los mejores parámetros para random forest
param_grid_rf = {
    "n_estimators": [100, 200],
    "max_depth": [10, 20, None],
    "min_samples_split": [2, 10],
    "min_samples_leaf": [1, 4]
}

grid_rf = GridSearchCV(
    RandomForestRegressor(random_state=0),
    param_grid_rf,
    cv=3,
    scoring="neg_mean_squared_error",
    n_jobs=-1
)

grid_rf.fit(X_train_arboles, y_train)

print("Mejores parámetros para Random Forest:")
print(grid_rf.best_params_)

In [ ]:
#Busca automáticamente los mejores parámetros para gradient boosting
param_grid_gb = {
    "n_estimators": [100, 200],
    "learning_rate": [0.05, 0.1],
    "max_depth": [3, 5]
}

grid_gb = GridSearchCV(
    GradientBoostingRegressor(random_state=0),
    param_grid_gb,
    cv=3,
    scoring="neg_mean_squared_error",
    n_jobs=-1
)

grid_gb.fit(X_train_arboles, y_train)

print("Mejores parámetros para Gradient Boosting:")
print(grid_gb.best_params_)